In [6]:
import pandas as pd;
import sqlite3
df=pd.read_csv("flipkart.csv")
df.head(5)
conn=sqlite3.connect("local_analytics.db")
df.to_sql("flipkart",conn,if_exists="replace",index=False)
%load_ext sql
%sql sqlite:///local_analytics.db


In [9]:
%config SqlMagic.style="_DEPRECATED_DEFAULT"

In [10]:
%%sql
SELECT product_name,category,brand,seller_city FROM flipkart LIMIT 5;

 * sqlite:///local_analytics.db
Done.


product_name,category,brand,seller_city
Adidas Ultra 664,Toys,Adidas,Hyderabad
LG Series 124,Fashion,LG,Mumbai
Redmi Model 35,Beauty,Redmi,Ahmedabad
Sony Edition 769,Toys,Sony,Delhi
Boat Prime 291,Home & Kitchen,Boat,Pune


In [16]:
%%sql
--Number of products in each category
SELECT category,COUNT(*) AS product_count FROM flipkart GROUP BY category ORDER BY product_count DESC ;

 * sqlite:///local_analytics.db
Done.


category,product_count
Toys,10151
Beauty,10094
Fashion,10080
Electronics,10052
Sports,9985
Appliances,9971
Mobiles,9904
Home & Kitchen,9763


In [17]:
%%sql
--TOP brands by number of products
SELECT brand,COUNT(*) AS Products_count FROM flipkart GROUP BY brand ORDER BY Products_count DESC LIMIT 10;

 * sqlite:///local_analytics.db
Done.


brand,Products_count
Puma,5409
Prestige,5401
Apple,5389
Reebok,5387
Nike,5358
Samsung,5345
LG,5345
Dell,5341
Redmi,5340
Philips,5340


In [22]:
%%sql
--Brands with average rating above 4
SELECT Brand,ROUND(AVG(rating),2) AS avg_rating FROM flipkart GROUP BY Brand HAVING avg_rating>3 ORDER BY avg_rating DESC;

 * sqlite:///local_analytics.db
Done.


brand,avg_rating
Sony,3.02
Samsung,3.02
Nike,3.01
Adidas,3.01


In [27]:
%%sql
--Estimated revenue by category
SELECT category,price,units_sold,price*units_sold AS revenue FROM flipkart GROUP BY category  ORDER BY revenue DESC;

 * sqlite:///local_analytics.db
Done.


category,price,units_sold,revenue
Sports,57120.4,4399,251272639.6
Electronics,53392.85,4594,245286752.9
Beauty,51214.5,2394,122607513.0
Mobiles,34527.08,2849,98367650.92
Fashion,30693.79,2703,82965314.37
Home & Kitchen,14181.34,4644,65858142.96
Appliances,18608.77,2671,49704024.67
Toys,35547.34,66,2346124.44


In [29]:
%%sql
--Top seller by units sold
SELECT seller,SUM(units_sold) AS  Total_units_sold FROM flipkart GROUP BY seller ORDER BY Total_units_sold DESC LIMIT 5;

 * sqlite:///local_analytics.db
Done.


seller,Total_units_sold
UrbanRetails,25330100
BestBuy,25241641
ValueKart,25197675
QuickShop,25181220
MegaStore,25153095


In [42]:
%%sql
--Products that are out of stock
SELECT product_name,price,category,stock_available FROM flipkart WHERE stock_available =0;

 * sqlite:///local_analytics.db
Done.


product_name,price,category,stock_available
Whirlpool Series 442,49195.12,Appliances,0
Adidas Prime 864,55662.82,Sports,0
Adidas Prime 472,49166.93,Sports,0
Puma Ultra 230,36656.27,Toys,0
Adidas Edition 595,18324.83,Fashion,0
Boat Edition 754,43336.17,Sports,0
Apple Edition 398,35384.21,Mobiles,0
Whirlpool Prime 988,25608.69,Appliances,0
Redmi Edition 16,57209.8,Fashion,0
Redmi Prime 722,6043.97,Sports,0


In [38]:
%%sql 
--Highly rated products with many reviews
SELECT product_name,rating,review_count FROM flipkart WHERE rating>=5 AND review_count>=45000 ORDER BY review_count DESC;

 * sqlite:///local_analytics.db
Done.


product_name,rating,review_count
Puma Edition 229,5.0,49990
Apple Model 642,5.0,49989
Dell Model 42,5.0,49979
Samsung Series 840,5.0,49962
Adidas Model 164,5.0,49936
Sony Series 366,5.0,49911
Boat Prime 768,5.0,49880
Puma Model 422,5.0,49849
Sony Model 269,5.0,49814
Nike Ultra 727,5.0,49781


In [39]:
%%sql
--Top 3 products within each category
SELECT * FROM(
    SELECT product_name,category,units_sold,
    RANK() OVER(
        PARTITION BY category
    ORDER BY units_sold DESC )
    AS product_rank 
    FROM flipkart )
AS ranked_products WHERE product_rank<=3;

 * sqlite:///local_analytics.db
Done.


product_name,category,units_sold,product_rank
Reebok Ultra 723,Appliances,4999,1
Whirlpool Edition 705,Appliances,4999,1
Puma Prime 388,Appliances,4997,3
Reebok Prime 402,Appliances,4997,3
Whirlpool Prime 218,Appliances,4997,3
LG Edition 658,Beauty,4999,1
Sony Series 442,Beauty,4999,1
Reebok Model 765,Beauty,4999,1
Sony Series 791,Beauty,4999,1
Reebok Edition 610,Beauty,4999,1


In [40]:
%%sql
--Compare product price with category average
SELECT product_name,category,price,AVG(price) OVER (PARTITION BY category) AS category_avg_price FROM flipkart;

 * sqlite:///local_analytics.db
Done.


product_name,category,price,category_avg_price
Puma Series 260,Appliances,18608.77,29826.05244107913
Prestige Prime 99,Appliances,52728.69,29826.05244107913
Nike Edition 42,Appliances,6955.08,29826.05244107913
Philips Series 40,Appliances,55702.15,29826.05244107913
Whirlpool Ultra 626,Appliances,4712.48,29826.05244107913
Puma Model 675,Appliances,33171.06,29826.05244107913
Whirlpool Series 442,Appliances,49195.12,29826.05244107913
Apple Prime 169,Appliances,6924.89,29826.05244107913
HP Prime 877,Appliances,15184.26,29826.05244107913
Prestige Prime 243,Appliances,43658.27,29826.05244107913


In [41]:
%%sql
-- Rank brands by sales with each category
SELECT * FROM (
    SELECT category,brand,SUM(units_sold) AS Total_units_sold,
    RANK() OVER(
        PARTITION BY category
        ORDER BY SUM(units_sold) DESC
    )AS Brand_rank 
    FROM flipkart
     GROUP BY category,brand)
AS ranked_brands WHERE Brand_rank<=3;

 * sqlite:///local_analytics.db
Done.


category,brand,Total_units_sold,Brand_rank
Appliances,Apple,1775034,1
Appliances,Samsung,1745130,2
Appliances,Puma,1736417,3
Beauty,LG,1769316,1
Beauty,Dell,1755956,2
Beauty,Redmi,1751155,3
Electronics,Nike,1890613,1
Electronics,Whirlpool,1764132,2
Electronics,Adidas,1726619,3
Fashion,Prestige,1820123,1
